In [ ]:
!pip install -q pymilvus
!pip install -q opik
!pip install -q pymilvus[milvus_lite]

   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 256.7/256.7 kB 10.0 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 18.8/18.8 MB 98.9 MB/s eta 0:00:00


In [ ]:
import os
import numpy as np
import pandas as pd
from typing import List, Tuple, Dict
from getpass import getpass
from tqdm import tqdm

import accelerate
import torch
from datasets import load_dataset
from sentence_transformers import SentenceTransformer
from pymilvus import MilvusClient

import openai
from openai import OpenAI

import opik
from opik.evaluation.metrics import Hallucination, AnswerRelevance

import warnings
warnings.filterwarnings('ignore')

In [ ]:
os.environ['HF_TOKEN'] = ''
os.environ['OPIK_API_KEY'] = ''
os.environ['OPENAI_API_KEY'] = ''

print('Environment Configured')

Environment Configured


# Loading Dataset

In [ ]:
# loading dataset from huggingface

dataset = load_dataset('m-ric/huggingface_doc') # list of dictionaries

print('----Dataset Loaded----')
print(f'Number of rows in the dataset: {dataset['train'].num_rows} rows')
print(f'Columns present in the dataset: {dataset['train'].features}')

print()
print(f'Sample row')
print(f'Text: {dataset['train'][0]['text'].replace("\n", " ")[:500]}')
print(f'Source: {dataset['train'][0]['source'][:500]}')

README.md:   0%|          | 0.00/21.0 [00:00<?, ?B/s]

huggingface_doc.csv: reconstructing file:   0%|          |  0.00B / 22.0MB            

huggingface_doc.csv: downloading bytes:           |  0.00B            

Generating train split:   0%|          | 0/2647 [00:00<?, ? examples/s]

----Dataset Loaded----
Number of rows in the dataset: 2647 rows
Columns present in the dataset: {'text': Value('string'), 'source': Value('string')}

Sample row
Text:  Create an Endpoint  After your first login, you will be directed to the [Endpoint creation page](https://ui.endpoints.huggingface.co/new). As an example, this guide will go through the steps to deploy [distilbert-base-uncased-finetuned-sst-2-english](https://huggingface.co/distilbert-base-uncased-finetuned-sst-2-english) for text classification.   ## 1. Enter the Hugging Face Repository ID and your desired endpoint name:  <img src="https://raw.githubusercontent.com/huggingface/hf-endpoints-docu
Source: huggingface/hf-endpoints-documentation/blob/main/docs/source/guides/create_endpoint.mdx


In [ ]:
# converting huggingface object into a python list

documents = []

for item in dataset['train']:
  documents.append({
      'text': item['text'],
      'source': item['source']
  })

print(f'Extracted {len(documents)} from the dataset')

Extracted 2647 from the dataset


# Chunking

In [ ]:
# we will be using chunking with overlap

def chunk_document(text: str, chunk_size: int = 1000, chunk_overlap: int=200) -> List[str]:

  chunks = []

  if not text.strip():
    return []

  if len(text) <= chunk_size:
    return [text.strip()]

  step = chunk_size - chunk_overlap
  if step <= 0:
    raise ValueError('Chunk Overlap must be strictly less than Chunk Size')

  start = 0

  while start < len(text):
    end = start + chunk_size
    chunks.append(text[start : end])

    start += step

  return chunks


def chunk_all_documents(documents: List[Dict], chunk_size: int = 1000, chunk_overlap: int = 200) -> List[Dict]:

  all_chunks = []
  chunk_id = 0

  for document in documents:
    text = document['text']
    chunks = chunk_document(text, chunk_size, chunk_overlap)

    for chunk in chunks:
      all_chunks.append({
          'chunk': chunk,
          'source': document['source'],
          'chunk_id': chunk_id
      })

      chunk_id += 1

  return all_chunks

In [ ]:
# Test your chunking implementation

test_text = "A" * 2500  # 2500 characters
test_chunks = chunk_document(test_text, chunk_size=1000, chunk_overlap=200)

print(f"Test: 2500 char text with chunk_size=1000, overlap=200")
print(f"Expected chunks: ~4")
print(f"Your chunks: {len(test_chunks)}")

if len(test_chunks) >= 3 and len(test_chunks) <= 5:
    print("✅ Chunking test passed!")
else:
    print("❌ Check your chunking implementation")

Test: 2500 char text with chunk_size=1000, overlap=200
Expected chunks: ~4
Your chunks: 4
✅ Chunking test passed!


In [ ]:
CHUNK_SIZE = 1000
CHUNK_OVERLAP = 200

chunks = chunk_all_documents(documents, CHUNK_SIZE, CHUNK_OVERLAP)

print(f'Created {len(chunks)} chunks from {len(documents)} documents')
print(f'Average chunks per document: {len(chunks) / len(documents):.2f}')

if chunks:
  print()
  print('-----Sample Chunk-----')
  print(f"Chunk ID: {chunks[0]['chunk_id']}")
  print(f"Chunk Text: {chunks[0]['chunk']}")
  print(f"Chunk Source: {chunks[0]['source']}")

Created 27993 chunks from 2647 documents
Average chunks per document: 10.58

-----Sample Chunk-----
Chunk ID: 0
Chunk Text:  Create an Endpoint

After your first login, you will be directed to the [Endpoint creation page](https://ui.endpoints.huggingface.co/new). As an example, this guide will go through the steps to deploy [distilbert-base-uncased-finetuned-sst-2-english](https://huggingface.co/distilbert-base-uncased-finetuned-sst-2-english) for text classification. 

## 1. Enter the Hugging Face Repository ID and your desired endpoint name:

<img src="https://raw.githubusercontent.com/huggingface/hf-endpoints-documentation/main/assets/1_repository.png" alt="select repository" />

## 2. Select your Cloud Provider and region. Initially, only AWS will be available as a Cloud Provider with the `us-east-1` and `eu-west-1` regions. We will add Azure soon, and if you need to test Endpoints with other Cloud Providers or regions, please let us know.

<img src="https://raw.githubusercontent.c

# Embeddings

In [ ]:
# defining the embeddings model

EMBEDDING_MODEL = 'BAAI/bge-small-en-v1.5'
embedding_model = SentenceTransformer(EMBEDDING_MODEL)

print(f"Loaded embedding model: {EMBEDDING_MODEL}")

# Test embedding
test_embedding = embedding_model.encode(["This is a test"], normalize_embeddings=True)
EMBEDDING_DIM = len(test_embedding[0])
print(f"Embedding dimension: {EMBEDDING_DIM}")

modules.json:   0%|          | 0.00/349 [00:00<?, ?B/s]

config_sentence_transformers.json:   0%|          | 0.00/124 [00:00<?, ?B/s]

README.md:   0%|          | 0.00/94.8k [00:00<?, ?B/s]

sentence_bert_config.json:   0%|          | 0.00/52.0 [00:00<?, ?B/s]

config.json:   0%|          | 0.00/743 [00:00<?, ?B/s]

...

vocab.txt:   0%|          | 0.00/232k [00:00<?, ?B/s]

tokenizer.json:   0%|          | 0.00/711k [00:00<?, ?B/s]

special_tokens_map.json:   0%|          | 0.00/125 [00:00<?, ?B/s]

config.json:   0%|          | 0.00/190 [00:00<?, ?B/s]

Loaded embedding model: BAAI/bge-small-en-v1.5
Embedding dimension: 384


In [ ]:
# writing a function to generate embeddings

def generate_embeddings(texts: List[str], model: SentenceTransformer, batch_size: int = 32) -> List[List[float]]:

  all_embeddings = []

  for i in range(0, len(texts), batch_size):
    batch = texts[i: i + batch_size]

    embeddings = model.encode(batch, normalize_embeddings = True,
                              show_progress_bar = True)

    all_embeddings.extend(embeddings.tolist())

  return all_embeddings

In [ ]:
# test to check if the embeddings generated are correct

test_texts = ["Hello world", "This is a test", "RAG is cool"]
test_embeddings = generate_embeddings(test_texts, embedding_model)

print(f"Generated {len(test_embeddings)} embeddings")
print(f"Embedding dimension: {len(test_embeddings[0]) if test_embeddings else 0}")

if len(test_embeddings) == 3 and len(test_embeddings[0]) == 384:
    print("✅ Embedding generation test passed!")
else:
    print("❌ Check your embedding implementation")

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Generated 3 embeddings
Embedding dimension: 384
✅ Embedding generation test passed!


In [ ]:
chunk_texts = [chunk['chunk'] for chunk in chunks]
embeddings = generate_embeddings(chunk_texts, embedding_model)

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

...

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

Batches:   0%|          | 0/1 [00:00<?, ?it/s]

In [ ]:
if embeddings:
  print(f'Embeddings Dimension: {len(embeddings[0])}')
  print(f'Fist 10 values of Sample Embedding: {embeddings[0][:10]}')

Embeddings Dimension: 384
Fist 10 values of Sample Embedding: [-0.07532959431409836, -0.027507992461323738, -0.03995613381266594, -0.040492136031389236, 0.033340033143758774, 0.04296518489718437, -0.043336279690265656, -0.04493821784853935, -0.05554318055510521, 0.02672027423977852]


# Vector Store

In [ ]:
MILVUS_DB_PATH = './hf_docs_milvus.db'
milvus_client = MilvusClient(uri = MILVUS_DB_PATH)

COLLECTION_NAME = "hf_documentation"
EMBEDDING_DIM = 384

print(f"Milvus client initialized with database: {MILVUS_DB_PATH}")

Milvus client initialized with database: ./hf_docs_milvus.db


In [ ]:
# setting up the vector store

def setup_milvus_collection(client : MilvusClient, collection_name: str, embedding_dim: str):

  if client.has_collection(collection_name):
    client.drop_collection(collection_name)

  client.create_collection(
      collection_name = collection_name,
      dimension = embedding_dim,
      metric = 'IP'
  )

setup_milvus_collection(milvus_client, COLLECTION_NAME ,EMBEDDING_DIM)

ERROR:grpc._server:Exception calling application: Method not implemented!
Traceback (most recent call last):
  File "/usr/local/lib/python3.12/dist-packages/grpc/_server.py", line 608, in _call_behavior
    response_or_iterator = behavior(argument, context)
                           ^^^^^^^^^^^^^^^^^^^^^^^^^^^
  File "/usr/local/lib/python3.12/dist-packages/pymilvus/grpc_gen/milvus_pb2_grpc.py", line 1264, in AllocTimestamp
    raise NotImplementedError('Method not implemented!')
NotImplementedError: Method not implemented!


In [ ]:
print(milvus_client.list_collections())
print(milvus_client.has_collection(COLLECTION_NAME))

print('Vector Store Intialised')

['hf_documentation']
True
Vector Store Intialised


In [ ]:
# definning a function to insert embeddings into the vector store

def insert_data_to_milvus(client: MilvusClient, collection_name: str, chunks: List[Dict],
                          embeddings: List[List[Dict]], batch_size: int = 100):

  total_inserted = 0

  data = [
      {
      'id': chunk['chunk_id'],
      'vector': embedding,
      'chunk': chunk['chunk'],
      'source': chunk['source']
     } for chunk, embedding in zip(chunks, embeddings)]

  for i in tqdm(range(0, len(data), batch_size)):
    batch = data[i : i+batch_size]
    result = client.insert(collection_name = collection_name, data = batch)
    total_inserted += result['insert_count']

  return total_inserted

In [ ]:
inserted_count = insert_data_to_milvus(milvus_client, COLLECTION_NAME, chunks, embeddings)

print(f"\nInserted {inserted_count} records into Milvus")

if inserted_count == len(chunks):
    print("✅ All chunks inserted successfully!")
else:
    print("❌ Not all chunks were inserted. Check your implementation.")


100%|██████████| 280/280 [00:17<00:00, 16.23it/s]


Inserted 27993 records into Milvus
✅ All chunks inserted successfully!


# Retrival

In [ ]:
# definning a retrival function to retrieve based on similarity search

def retrieve_documents(query: str, client: MilvusClient, collection_name: str,
                       embedding_model: SentenceTransformer, top_k : int = 5) -> List[Dict]:

  retrieved_docs = []

  query_embedding = embedding_model.encode([query], normalize_embeddings = True).tolist()[0]

  search_results = client.search(
      collection_name = collection_name,
      data = [query_embedding],
      limit = top_k,
      search_params={"metric_type": "IP", "params": {}},
      output_fields=["chunk", "source"]
  )

  for result in search_results[0]:
        retrieved_docs.append({
            "text": result["entity"]["chunk"],
            "source": result["entity"]["source"],
            "score": result["distance"]
        })

  return retrieved_docs

In [ ]:
# Test retrieval

test_query = "How do I fine-tune a transformer model?"

retrieved = retrieve_documents(
    query=test_query,
    client=milvus_client,
    collection_name=COLLECTION_NAME,
    embedding_model=embedding_model,
    top_k=3
)

print(f"Query: {test_query}")
print(f"\nRetrieved {len(retrieved)} documents:")
for i, doc in enumerate(retrieved):
    print(f"\n--- Document {i+1} (Score: {doc.get('score', 'N/A')}) ---")
    print(f"Source: {doc.get('source', 'N/A')}")
    print(f"Text: {doc.get('text', 'N/A')[:300]}...")

if len(retrieved) == 3 and all('text' in d for d in retrieved):
    print("\n✅ Retrieval test passed!")
else:
    print("\n❌ Check your retrieval implementation")

Query: How do I fine-tune a transformer model?

Retrieved 3 documents:

--- Document 1 (Score: 0.7614539861679077) ---
Source: huggingface/blog/blob/main/moe.md
Text: on does not degrade quality.">
  <figcaption>Using selective precision does not degrade quality and enables faster models</figcaption>
</figure>

This [notebook](https://colab.research.google.com/drive/1aGGVHZmtKmcNBbAwa9hbu58DDpIuB5O4?usp=sharing) showcases fine-tuning Switch Transformers for summa...

--- Document 2 (Score: 0.7431504130363464) ---
Source: huggingface/transformers/blob/main/docs/source/en/index.md
Text:  |         ✅         |      ❌      |
|                 [Swin Transformer V2](model_doc/swinv2)                  |       ✅        |         ❌         |      ❌      |
|                       [Swin2SR](model_doc/swin2sr)                       |       ✅        |         ❌         |      ❌      |
|      ...

--- Document 3 (Score: 0.7406573295593262) ---
Source: huggingface/peft/blob/main/docs/source/task_guid

# Generation

In [ ]:
# intialising openai

openai_client = OpenAI()

LLM_MODEL = 'gpt-4o-mini'

print(f'Using OpenAI Model: {LLM_MODEL}')

Using OpenAI Model: gpt-4o-mini


In [ ]:
PROMPT_TEMPLATE = """Use the following pieces of information enclosed in <context> tags to provide an answer to the question enclosed in <question> tags.
If the context doesn't contain enough information to answer the question, say "I don't have enough information to answer this question."

<context>
{context}
</context>

<question>
{question}
</question>

Answer:"""

In [ ]:
# definning answer generation

def generate_answer(query: str, retrieved_docs: List[Dict], max_new_tokens: int = 256) -> Dict:

    context = "\n\n".join([doc["text"] for doc in retrieved_docs])
    prompt = PROMPT_TEMPLATE.format(context=context, question=query)

    response = openai_client.chat.completions.create(
        model=LLM_MODEL,
        messages=[{"role": "user", "content": prompt}],
        max_tokens=max_new_tokens,
        temperature=0.7,
        top_p=0.9
    )
    answer = response.choices[0].message.content.strip()

    return {
        "query": query,
        "answer": answer,
        "context": context,
        "retrieved_docs": retrieved_docs
    }

In [ ]:
# Test generation
test_query = "How do I fine-tune a transformer model?"

# Retrieve relevant documents
retrieved = retrieve_documents(
    query=test_query,
    client=milvus_client,
    collection_name=COLLECTION_NAME,
    embedding_model=embedding_model,
    top_k=3
)

# Generate answer
result = generate_answer(
    query=test_query,
    retrieved_docs=retrieved
)

print(f"Question: {result['query']}")
print(f"\nAnswer: {result['answer']}")

if result['answer'] and len(result['answer']) > 10:
    print("\n✅ Generation test passed!")
else:
    print("\n❌ Check your generation implementation")

Question: How do I fine-tune a transformer model?

Answer: To fine-tune a transformer model, you can use the `transformers.Trainer` class along with `transformers.TrainingArguments`. Here is a general outline of the steps:

1. **Set Up Training Arguments**: Define the training parameters using `TrainingArguments`. You can specify parameters like evaluation strategy, save strategy, learning rate, batch size, and number of epochs. For example:

   ```python
   from transformers import TrainingArguments

   model_name = model_checkpoint.split("/")[-1]
   batch_size = 128

   args = TrainingArguments(
       f"{model_name}-finetuned-lora-food101",
       remove_unused_columns=False,
       evaluation_strategy="epoch",
       save_strategy="epoch",
       learning_rate=5e-3,
       per_device_train_batch_size=batch_size,
       gradient_accumulation_steps=4,
       per_device_eval_batch_size=batch_size,
       fp16=True,
       num_train_epochs=5,
       logging_steps=10,
       load_best_m

In [ ]:
# Complete RAG pipeline function

def rag_query(
    query: str,
    client: MilvusClient,
    collection_name: str,
    embedding_model: SentenceTransformer,
    top_k: int = 5,
    max_new_tokens: int = 256
) -> Dict:
    """
    Complete RAG pipeline: retrieve then generate.
    """
    # Retrieve
    retrieved_docs = retrieve_documents(
        query=query,
        client=client,
        collection_name=collection_name,
        embedding_model=embedding_model,
        top_k=top_k
    )

    # Generate
    result = generate_answer(
        query=query,
        retrieved_docs=retrieved_docs,
        max_new_tokens=max_new_tokens
    )

    return result

In [ ]:
# Test complete pipeline with multiple queries

test_queries = [
    "What is the Trainer class in transformers?",
    "How do I load a dataset from HuggingFace?",
    "What is Gradio used for?"
]

for query in test_queries:
    print(f"\n{'='*60}")
    result = rag_query(
        query=query,
        client=milvus_client,
        collection_name=COLLECTION_NAME,
        embedding_model=embedding_model,
        top_k=3
    )
    print(f"Q: {result['query']}")
    print(f"A: {result['answer']}")


Q: What is the Trainer class in transformers?
A: The `Trainer` class in the Transformers library is a complete training and evaluation loop for PyTorch models. It simplifies the training process by allowing users to pass the necessary components for training, such as the model, tokenizer, dataset, evaluation function, and training hyperparameters. The `Trainer` class handles the rest, making it easier to start training without the need to manually write a training loop. Additionally, it is highly customizable, offering a variety of training options to tailor the training process to specific needs.

Q: How do I load a dataset from HuggingFace?
A: To load a dataset from Hugging Face, you can use the 🤗 Datasets library, which allows you to load a dataset in a single line of code. Ensure you have the library installed, and then you can access datasets for various tasks such as Audio, Computer Vision, and Natural Language Processing (NLP). For example, you can load an image dataset organiz

# Evaluation

In [ ]:
# definning evaluation metrics

hallucination_metric = Hallucination()
answer_relevance_metric = AnswerRelevance()

def evaluate_rag(result: Dict) -> Dict:

  context = [doc['text'] for doc in result['retrieved_docs']]

  hallucination_result = hallucination_metric.score(
      input = result['query'],
      output = result['answer'],
      context = context
  )

  answer_relevance_result = answer_relevance_metric.score(
      input = result['query'],
      output = result['answer'],
      context = context
  )

  return {
        **result,
        "hallucination_score": hallucination_result.value,
        "hallucination_reason": hallucination_result.reason,
        "answer_relevance_score": answer_relevance_result.value,
        "answer_relevance_reason": answer_relevance_result.reason
    }

In [ ]:
# writing a function to evaluate the rag pipeline

def evaluate_rag_pipeline(queries: List[str], top_k: int = 3) -> pd.DataFrame:
    eval_results = []

    for query in tqdm(queries):
        result = rag_query(
            query=query,
            client=milvus_client,
            collection_name=COLLECTION_NAME,
            embedding_model=embedding_model,
            top_k=top_k
        )
        scored = evaluate_rag(result)
        eval_results.append({
            "query": scored["query"],
            "answer": scored["answer"],
            "hallucination_score": scored["hallucination_score"],
            "answer_relevance_score": scored["answer_relevance_score"],
        })

    return pd.DataFrame(eval_results)


test_queries = [
    "What is the Trainer class in transformers?",
    "How do I load a dataset from HuggingFace?",
    "What is Gradio used for?",
    "How do I fine-tune a transformer model?"
]

eval_df = evaluate_rag_pipeline(test_queries)
print(eval_df)

print(f"\nAverage hallucination rate: {eval_df['hallucination_score'].mean():.2%}")
print(f"Average answer relevance: {eval_df['answer_relevance_score'].mean():.2f}")

100%|██████████| 4/4 [01:08<00:00, 17.16s/it]

                                        query  \
0  What is the Trainer class in transformers?   
1   How do I load a dataset from HuggingFace?   
2                    What is Gradio used for?   
3     How do I fine-tune a transformer model?   

                                              answer  hallucination_score  \
0  The [`Trainer`] class in the Transformers libr...                  0.0   
1  To load a dataset from Hugging Face, you can u...                  0.0   
2  Gradio is used to create interactive applicati...                  0.0   
3  To fine-tune a transformer model, you can use ...                  0.0   

   answer_relevance_score  
0                    1.00  
1                    0.60  
2                    0.92  
3                    0.90  

Average hallucination rate: 0.00%
Average answer relevance: 0.85
